# Detect face masks in an uploaded video

Run all cells. A file-selection window will open so you can choose a video from your computer. The processed video is saved as `mask_detection_output.mp4` and displayed below.

In [1]:
from pathlib import Path
from tkinter import Tk, filedialog

import cv2
import numpy as np
from IPython.display import Video, display
from tensorflow.keras.applications.mobilenet_v2 import preprocess_input
from tensorflow.keras.models import load_model
from tensorflow.keras.preprocessing.image import img_to_array
import os

FACE_CONFIDENCE = 0.21  # Reject weak false face detections
NMS_THRESHOLD = 0.30     # Remove duplicate overlapping boxes
MIN_FACE_SIZE = 24
MAX_FACE_HEIGHT_RATIO = 0.55
CLASS_CONFIDENCE = 0.65  # Otherwise report Uncertain
MAX_OUTPUT_WIDTH = 960   # Preserve more detail than 400 pixels
PLAYBACK_SPEED = 0.50    # 0.50 = half speed; 1.00 = normal speed
OUTPUT_VIDEO = "mask_detection_output_fixed.mp4"

In [2]:
# Open a native file-selection window. Rerun this cell to choose another video.
dialog = Tk()
dialog.withdraw()
dialog.attributes("-topmost", True)
dialog.update()
try:
    selected_video = filedialog.askopenfilename(
        parent=dialog,
        title="Select a video to check",
        filetypes=[
            ("Video files", ("*.mp4", "*.avi", "*.mov", "*.mkv", "*.m4v")),
            ("All files", "*.*"),
        ],
    )
finally:
    dialog.destroy()

if not selected_video:
    raise RuntimeError("No video was selected. Rerun this cell and choose a video.")

input_path = Path(selected_video)
print(f"[INFO] selected {input_path}")

[INFO] selected /Users/thawfeek/Downloads/Chrome Download/video_duration_minimun_seco.mp4


In [3]:
def detect_and_predict_mask(
    frame, face_net, mask_net, confidence_threshold=0.60,
    nms_threshold=0.30, min_face_size=24, max_face_height_ratio=0.55
):
    h, w = frame.shape[:2]
    blob = cv2.dnn.blobFromImage(
        frame, 1.0, (300, 300), (104.0, 177.0, 123.0)
    )

    face_net.setInput(blob)
    detections = face_net.forward()
    candidate_boxes = []
    candidate_scores = []

    for i in range(detections.shape[2]):
        confidence = float(detections[0, 0, i, 2])
        if confidence < confidence_threshold:
            continue

        box = detections[0, 0, i, 3:7] * np.array([w, h, w, h])
        start_x, start_y, end_x, end_y = box.astype("int")
        start_x, start_y = max(0, start_x), max(0, start_y)
        end_x, end_y = min(w - 1, end_x), min(h - 1, end_y)
        box_width = end_x - start_x
        box_height = end_y - start_y

        if box_width < min_face_size or box_height < min_face_size:
            continue
        aspect_ratio = box_width / box_height
        if not 0.55 <= aspect_ratio <= 1.35:
            continue
        if box_height > h * max_face_height_ratio:
            continue

        candidate_boxes.append([start_x, start_y, box_width, box_height])
        candidate_scores.append(confidence)

    if not candidate_boxes:
        return [], np.empty((0, 2), dtype="float32")

    kept_indices = cv2.dnn.NMSBoxes(
        candidate_boxes, candidate_scores, confidence_threshold, nms_threshold
    )
    faces = []
    locs = []

    for index in np.asarray(kept_indices).reshape(-1):
        start_x, start_y, box_width, box_height = candidate_boxes[int(index)]
        end_x = start_x + box_width
        end_y = start_y + box_height
        face = frame[start_y:end_y, start_x:end_x]
        if face.size == 0:
            continue

        face = cv2.cvtColor(face, cv2.COLOR_BGR2RGB)
        face = cv2.resize(face, (224, 224))
        face = img_to_array(face)
        faces.append(preprocess_input(face))
        locs.append((start_x, start_y, end_x, end_y))

    if not faces:
        return [], np.empty((0, 2), dtype="float32")

    faces = np.array(faces, dtype="float32")
    predictions = mask_net.predict(faces, batch_size=32, verbose=0)
    return locs, predictions

In [4]:
# Support starting Jupyter either in this folder or in the repository root.
# project_dir = Path.cwd()
# if not (project_dir / "face_detector").is_dir():
#     project_dir = project_dir / "FaceMask-Detection"

# face_detector_dir = project_dir / "face_detector"
# prototxt_path = face_detector_dir / "deploy.prototxt"
# weights_path = face_detector_dir / "res10_300x300_ssd_iter_140000.caffemodel"
# model_path = project_dir / "mask_detector.h5"
# for required_path in (prototxt_path, weights_path, model_path):
#     if not required_path.is_file():
#         raise FileNotFoundError(f"Required model file not found: {required_path.resolve()}")

prototxt_path = os.path.join("face_detector", "deploy.prototxt")
weights_path = os.path.join("face_detector", "res10_300x300_ssd_iter_140000.caffemodel")
model_path = "mask_detector.h5"



print("[INFO] loading face detector model...")
face_net = cv2.dnn.readNet(str(prototxt_path), str(weights_path))

print("[INFO] loading face mask detector model...")
mask_net = load_model(model_path, compile=False)

[INFO] loading face detector model...
[INFO] loading face mask detector model...


In [ ]:
project_dir = Path.cwd()
output_path = project_dir / OUTPUT_VIDEO

if not input_path.is_file():
    raise FileNotFoundError(f"Selected video not found: {input_path.resolve()}")

capture = cv2.VideoCapture(str(input_path))
if not capture.isOpened():
    raise RuntimeError(f"OpenCV could not open: {input_path.resolve()}")

source_width = int(capture.get(cv2.CAP_PROP_FRAME_WIDTH))
source_height = int(capture.get(cv2.CAP_PROP_FRAME_HEIGHT))
if source_width <= 0 or source_height <= 0:
    capture.release()
    raise RuntimeError("Could not read the input video's dimensions.")

source_fps = capture.get(cv2.CAP_PROP_FPS)
if not source_fps or source_fps <= 0:
    source_fps = 25.0
output_fps = max(1.0, source_fps * PLAYBACK_SPEED)

output_width = min(MAX_OUTPUT_WIDTH, source_width)
output_height = round(source_height * output_width / source_width)
# Some video codecs require even frame dimensions.
output_width -= output_width % 2
output_height -= output_height % 2

writer = cv2.VideoWriter(
    str(output_path),
    cv2.VideoWriter_fourcc(*"mp4v"),
    output_fps,
    (output_width, output_height),
)
if not writer.isOpened():
    capture.release()
    raise RuntimeError(f"Could not create output video: {output_path.resolve()}")

print(f"[INFO] processing {input_path.name}...")
print(f"[INFO] playback: {PLAYBACK_SPEED:.2f}x ({source_fps:.2f} -> {output_fps:.2f} FPS)")
processed_frames = 0
try:
    while True:
        success, frame = capture.read()
        if not success:
            break

        frame = cv2.resize(frame, (output_width, output_height))
        locs, preds = detect_and_predict_mask(
            frame, face_net, mask_net, FACE_CONFIDENCE, NMS_THRESHOLD,
            MIN_FACE_SIZE, MAX_FACE_HEIGHT_RATIO
        )

        for box, prediction in zip(locs, preds):
            start_x, start_y, end_x, end_y = box
            mask_score, no_mask_score = map(float, prediction)
            best_score = max(mask_score, no_mask_score)

            if best_score < CLASS_CONFIDENCE:
                label = f"Uncertain {best_score * 100:.0f}%"
                color = (0, 215, 255)
            elif mask_score > no_mask_score:
                label = f"Mask {mask_score * 100:.0f}%"
                color = (0, 255, 0)
            else:
                label = f"No Mask {no_mask_score * 100:.0f}%"
                color = (0, 0, 255)

            text_y = max(start_y - 10, 15)
            cv2.putText(
                frame, label, (start_x, text_y),
                cv2.FONT_HERSHEY_SIMPLEX, 0.45, color, 2
            )
            cv2.rectangle(frame, (start_x, start_y), (end_x, end_y), color, 2)

        writer.write(frame)
        processed_frames += 1
finally:
    capture.release()
    writer.release()

if processed_frames == 0:
    raise RuntimeError("The input video contained no readable frames.")

print(f"[INFO] processed {processed_frames} frames")
print(f"[INFO] saved result to {output_path.resolve()}")
display(Video(str(output_path), embed=True))

[INFO] processing video_duration_minimun_seco.mp4...
[INFO] playback: 0.50x (24.00 -> 12.00 FPS)
[INFO] processed 480 frames
[INFO] saved result to /Users/thawfeek/Downloads/Ai-Trained-Model/BestLabz-AiModels/FaceMask-Detection/mask_detection_output_fixed.mp4


: 